# EDA: Análisis Exploratorio de Datos

Este conjunto de datos Default of Credit Card Clients (UCI Machine Learning Repository) contiene información de 30,000 clientes de tarjetas de crédito en Taiwán, recolectada en 2005. El objetivo original del dataset es predecir si un cliente incurrirá en un incumplimiento de pago (default) al mes siguiente, a partir de su límite de crédito, información demográfica, historial de pagos de los últimos 6 meses y montos facturados en ese mismo periodo.

La variable objetivo es `default payment next month`, que indica si el cliente incurrió **(1)** o no **(0)** en incumplimiento de pago al mes siguiente. Esto permite plantear el problema como una tarea de **clasificación binaria**.

Este EDA revisa explícitamente los duplicados (y los **elimina**), trata las categorías no oficiales, controla los outliers antes de calcular correlación y VIF, y cada gráfico interactivo va acompañado de su interpretación, con una versión **básica** (palabras sencillas) y una **técnica**. En la Parte 5 se aplica y se guarda el preprocesamiento que resuelve todos los hallazgos, de modo que el dataset que reciben los modelos ya sale limpio de aquí.

In [1]:
import sys
from pathlib import Path

PROJECT_ROOT = Path.cwd().parent
if str(PROJECT_ROOT) not in sys.path:
    sys.path.insert(0, str(PROJECT_ROOT))

from src import config

# Recolección y lectura de los datos, configuración general

import pandas as pd
import numpy as np

import plotly.express as px
import plotly.graph_objects as go
from plotly.subplots import make_subplots
import plotly.io as pio

from scipy import stats
from statsmodels.stats.outliers_influence import variance_inflation_factor

from sklearn.ensemble import RandomForestClassifier
from sklearn.model_selection import train_test_split
import shap

from src.eda_widgets import show_with_interpretation

pd.options.display.float_format = "{:,.4f}".format

# ---- Paleta  ----
DEEP_NAVY = "#0C1A41"
NAVY      = "#1B3071"
PALE_GOLD = "#E8C871"
WARM_GOLD = "#C9930C"
CREAM     = "#F9F0DE"

pio.templates["navy_gold"] = pio.templates["plotly_white"]
pio.templates["navy_gold"].layout.colorway = [DEEP_NAVY, WARM_GOLD, NAVY, PALE_GOLD, "#7A8AA8"]
pio.templates["navy_gold"].layout.paper_bgcolor = "white"
pio.templates["navy_gold"].layout.plot_bgcolor = CREAM
pio.templates["navy_gold"].layout.font = dict(color=DEEP_NAVY, family="Arial")
pio.templates.default = "navy_gold"
pio.renderers.default = "notebook_connected"  # para que los gráficos se rendericen como HTML embebido en Jupyter Book

DIVERGING_NG = [[0.0, NAVY], [0.5, CREAM], [1.0, WARM_GOLD]]


C:\Users\valef\anaconda3\envs\creditcard\Lib\site-packages\tqdm\auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm


## Tipo y descripción de las variables

El conjunto de datos está compuesto por variables numéricas continuas y variables categóricas (algunas codificadas numéricamente).

| Variable                                     | Tipo                        | Descripción                                                                                                                                                                                                                                                                                                                                   |
| -------------------------------------------- | --------------------------- | --------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------- |
| **LIMIT_BAL**                                | Numérica continua           | Monto del crédito otorgado, incluyendo crédito individual y familiar/suplementario, en dólares taiwaneses (NT$).                                                                                                                                                                                                                              |
| **SEX**                                      | Categórica                  | Género del cliente. `1` = hombre, `2` = mujer.                                                                                                                                                                                                                                                                                                |
| **EDUCATION**                                | Categórica                  | Nivel educativo. `1` = posgrado, `2` = universidad, `3` = secundaria, `4` = otros. También existen los códigos `0`, `5` y `6`, no documentados oficialmente por la fuente.                                                                                                                                                                    |
| **MARRIAGE**                                 | Categórica                  | Estado civil. `1` = casado, `2` = soltero, `3` = otros. También existe el código `0`, no documentado.                                                                                                                                                                                                                                         |
| **AGE**                                      | Numérica discreta           | Edad del cliente en años.                                                                                                                                                                                                                                                                                                                     |
| **PAY_0, PAY_2, PAY_3, PAY_4, PAY_5, PAY_6** | Numérica discreta / ordinal | Estado de pago mensual de septiembre a abril de 2005 (`PAY_0` = mes más reciente). `-1` = pago puntual, `1-9` = meses de atraso. Los valores `-2` y `0` aparecen en la documentación original sin una definición unívoca; se conservan como están por ser mayoritarios, pero su interpretación exacta es una limitación conocida del dataset. |
| **BILL_AMT1 a BILL_AMT6**                    | Numérica continua           | Monto facturado en el estado de cuenta de cada uno de los últimos 6 meses.                                                                                                                                                                                                                                                                    |
| **PAY_AMT1 a PAY_AMT6**                      | Numérica continua           | Monto efectivamente pagado por el cliente en cada uno de los últimos 6 meses.                                                                                                                                                                                                                                                                 |
| **default payment next month**               | Categórica binaria          | **Variable objetivo.** `1` = incurrió en incumplimiento al mes siguiente, `0` = no incurrió.                                                                                                                                                                                                                                                  |


In [2]:
df = pd.read_excel(config.RAW_DATA_PATH, header=1)
df = df.rename(columns={"default payment next month": "default_payment_next_month"})
df = df.set_index("ID")

target = "default_payment_next_month"
num_cols = ["LIMIT_BAL", "AGE",
            "PAY_0", "PAY_2", "PAY_3", "PAY_4", "PAY_5", "PAY_6",
            "BILL_AMT1", "BILL_AMT2", "BILL_AMT3", "BILL_AMT4", "BILL_AMT5", "BILL_AMT6",
            "PAY_AMT1", "PAY_AMT2", "PAY_AMT3", "PAY_AMT4", "PAY_AMT5", "PAY_AMT6"]
cat_cols = ["SEX", "EDUCATION", "MARRIAGE"]

print("Dimensiones de los datos:", df.shape)
df.head()


Dimensiones de los datos: (30000, 24)


,LIMIT_BAL,SEX,EDUCATION,MARRIAGE,AGE,PAY_0,PAY_2,PAY_3,PAY_4,PAY_5,...,BILL_AMT4,BILL_AMT5,BILL_AMT6,PAY_AMT1,PAY_AMT2,PAY_AMT3,PAY_AMT4,PAY_AMT5,PAY_AMT6,default_payment_next_month
ID,,,,,,,,,,,,,,,,,,,,,
1,20000,2,2,1,24,2,2,-1,-1,-2,...,0,0,0,0,689,0,0,0,0,1
2,120000,2,2,2,26,-1,2,0,0,0,...,3272,3455,3261,0,1000,1000,1000,0,2000,1
3,90000,2,2,2,34,0,0,0,0,0,...,14331,14948,15549,1518,1500,1000,1000,1000,5000,0
4,50000,2,2,1,37,0,0,0,0,0,...,28314,28959,29547,2000,2019,1200,1100,1069,1000,0
5,50000,1,2,1,57,-1,0,-1,0,0,...,20940,19146,19131,2000,36681,10000,9000,689,679,0


In [3]:
df.info()

<class 'pandas.DataFrame'>
RangeIndex: 30000 entries, 1 to 30000
Data columns (total 24 columns):
 #   Column                      Non-Null Count  Dtype
---  ------                      --------------  -----
 0   LIMIT_BAL                   30000 non-null  int64
 1   SEX                         30000 non-null  int64
 2   EDUCATION                   30000 non-null  int64
 3   MARRIAGE                    30000 non-null  int64
 4   AGE                         30000 non-null  int64
 5   PAY_0                       30000 non-null  int64
 6   PAY_2                       30000 non-null  int64
 7   PAY_3                       30000 non-null  int64
 8   PAY_4                       30000 non-null  int64
 9   PAY_5                       30000 non-null  int64
 10  PAY_6                       30000 non-null  int64
 11  BILL_AMT1                   30000 non-null  int64
 12  BILL_AMT2                   30000 non-null  int64
 13  BILL_AMT3                   30000 non-null  int64
 14  BILL_AMT4        

### Valores nulos y duplicados

In [4]:
print("Valores nulos totales:", df.isnull().sum().sum())
print()
print("Filas completamente duplicadas (considerando todas las variables, sin el ID):")
print(df.duplicated().sum())
df[df.duplicated(keep=False)].sort_values(num_cols).head(6)


Valores nulos totales: 0

Filas completamente duplicadas (considerando todas las variables, sin el ID):
35


,LIMIT_BAL,SEX,EDUCATION,MARRIAGE,AGE,PAY_0,PAY_2,PAY_3,PAY_4,PAY_5,...,BILL_AMT4,BILL_AMT5,BILL_AMT6,PAY_AMT1,PAY_AMT2,PAY_AMT3,PAY_AMT4,PAY_AMT5,PAY_AMT6,default_payment_next_month
ID,,,,,,,,,,,,,,,,,,,,,
12431,20000,1,2,2,24,2,2,4,4,4,...,1650,1650,1650,0,0,0,0,0,0,1
14295,20000,1,2,2,24,2,2,4,4,4,...,1650,1650,1650,0,0,0,0,0,0,1
7171,50000,2,1,2,23,1,-2,-2,-2,-2,...,0,0,0,0,0,0,0,0,0,0
17033,50000,2,1,2,23,1,-2,-2,-2,-2,...,0,0,0,0,0,0,0,0,0,0
1760,50000,1,2,2,26,1,-2,-2,-2,-2,...,0,0,0,0,0,0,0,0,0,0
10251,50000,1,2,2,26,1,-2,-2,-2,-2,...,0,0,0,0,0,0,0,0,0,0


In [5]:
n_antes = len(df)
df = df.drop_duplicates()
print(f"Filas antes: {n_antes:,} | duplicadas eliminadas: {n_antes - len(df)} | filas ahora: {len(df):,}")
print("Duplicados restantes:", int(df.duplicated().sum()))

Filas antes: 30,000 | duplicadas eliminadas: 35 | filas ahora: 29,965
Duplicados restantes: 0


No hay valores nulos en ninguna variable: a diferencia del dataset *Give Me Some Credit*, aquí no se requiere imputación.

Sí se detectan **35 filas con exactamente los mismos valores en todas las variables** (excluyendo el `ID`, que es único por construcción). Es plausible que parte de ellas sean clientes distintos con el mismo perfil, porque hay varias variables categóricas/discretas con pocos valores posibles (`SEX`, `EDUCATION`, `MARRIAGE`, `PAY_x`). Aun así **se eliminan**: si una fila y su copia exacta quedan repartidas entre entrenamiento y validación, el modelo se evalúa sobre un caso que ya vio, lo que infla artificialmente la métrica (fuga de información). Eliminarlas solo cuesta 35 de 30,000 filas (0.12%). Se conserva la primera aparición de cada grupo, y todo el análisis posterior se hace sobre el dataset ya sin duplicados.

### Categorías no documentadas / valores centinela

In [6]:
print("EDUCATION:\n", df["EDUCATION"].value_counts().sort_index())
print("\nMARRIAGE:\n", df["MARRIAGE"].value_counts().sort_index())
print()
for c in ["PAY_0", "PAY_2", "PAY_3", "PAY_4", "PAY_5", "PAY_6"]:
    print(c, dict(sorted(df[c].value_counts().to_dict().items())))


EDUCATION:
 EDUCATION
0       14
1    10563
2    14019
3     4915
4      123
5      280
6       51
Name: count, dtype: int64

MARRIAGE:
 MARRIAGE
0       54
1    13643
2    15945
3      323
Name: count, dtype: int64

PAY_0 {-2: 2750, -1: 5682, 0: 14737, 1: 3667, 2: 2666, 3: 322, 4: 76, 5: 26, 6: 11, 7: 9, 8: 19}
PAY_2 {-2: 3752, -1: 6046, 0: 15730, 1: 28, 2: 3926, 3: 326, 4: 99, 5: 25, 6: 12, 7: 20, 8: 1}
PAY_3 {-2: 4055, -1: 5934, 0: 15764, 1: 4, 2: 3819, 3: 240, 4: 75, 5: 21, 6: 23, 7: 27, 8: 3}
PAY_4 {-2: 4318, -1: 5683, 0: 16455, 1: 2, 2: 3159, 3: 180, 4: 68, 5: 35, 6: 5, 7: 58, 8: 2}
PAY_5 {-2: 4516, -1: 5535, 0: 16947, 2: 2626, 3: 178, 4: 83, 5: 17, 6: 4, 7: 58, 8: 1}
PAY_6 {-2: 4865, -1: 5736, 0: 16286, 2: 2766, 3: 184, 4: 48, 5: 13, 6: 19, 7: 46, 8: 2}


`EDUCATION` trae tres códigos (**0, 5, 6**) que no forman parte de la documentación oficial (1=posgrado, 2=universidad, 3=secundaria, 4=otros); en conjunto representan **345 registros (1.2%)**. `MARRIAGE` trae un código **0** no documentado, con **54 registros (0.18%)**.

En ambos casos se trata de una fracción pequeña de la muestra, así que en vez de eliminarlas (lo que descartaría información del resto de variables de esos clientes) se **reagrupan dentro de la categoría "Otros"** ya existente (`EDUCATION = 4`, `MARRIAGE = 3`), que es semánticamente el destino más razonable para códigos no identificados.

Las variables `PAY_x` muestran una alta concentración en **0** (entre el 49% y el 57% de los casos según el mes) y en **-1** (18-20%), seguidos por **-2** (9-16%). Como se explicó arriba, la definición exacta de estos dos códigos no está estandarizada en la fuente original. Se conservan tal cual (no se recodifican ni se eliminan) porque representan a la mayoría de las observaciones y contienen información real (clientes sin atraso), pero se deja constancia de la ambigüedad para no sobre-interpretar resultados que dependan de la frontera exacta entre "0" y "-1".


In [7]:
df["EDUCATION"] = df["EDUCATION"].replace({0: 4, 5: 4, 6: 4})
df["MARRIAGE"] = df["MARRIAGE"].replace({0: 3})

print("EDUCATION tras reagrupar:\n", df["EDUCATION"].value_counts().sort_index())
print("\nMARRIAGE tras reagrupar:\n", df["MARRIAGE"].value_counts().sort_index())


EDUCATION tras reagrupar:
 EDUCATION
1    10563
2    14019
3     4915
4      468
Name: count, dtype: int64

MARRIAGE tras reagrupar:
 MARRIAGE
1    13643
2    15945
3      377
Name: count, dtype: int64


### Montos de facturación negativos

In [8]:
bill_cols = [c for c in num_cols if c.startswith("BILL_AMT")]
neg_counts = (df[bill_cols] < 0).sum()
print("Registros con BILL_AMT negativo, por mes:")
print(neg_counts)
print("\nTotal de filas con al menos un BILL_AMT negativo:", (df[bill_cols] < 0).any(axis=1).sum())


Registros con BILL_AMT negativo, por mes:
BILL_AMT1    590
BILL_AMT2    669
BILL_AMT3    655
BILL_AMT4    675
BILL_AMT5    655
BILL_AMT6    688
dtype: int64

Total de filas con al menos un BILL_AMT negativo: 1930


Cada mes, entre el **2.0% y el 2.3%** de los registros tiene un monto de facturación (`BILL_AMT`) **negativo**, y en total **6.4% de los clientes** (1,930 filas) tiene al menos un mes negativo. Esto **no se trata como un error**: un saldo negativo en un estado de cuenta de tarjeta de crédito es económicamente válido y suele indicar que el cliente pagó de más el mes anterior (saldo a favor). No se elimina ni se corrige; en la Parte 5 queda resumido en la variable derivada `N_CREDIT_BALANCE_MONTHS` (número de meses con saldo a favor).

## Análisis de la variable objetivo

In [9]:
conteo_target = df[target].value_counts().sort_index()
prop_target = df[target].value_counts(normalize=True).sort_index()

fig = go.Figure(go.Bar(
    x=["No default (0)", "Default (1)"],
    y=conteo_target.values,
    marker_color=[DEEP_NAVY, DEEP_NAVY],
    text=[f"{v:,} ({p:.1%})" for v, p in zip(conteo_target.values, prop_target.values)],
    textposition="outside",
    hovertemplate="%{x}<br>%{y:,} clientes<extra></extra>",
))
fig.update_layout(
    title="Distribución de la variable objetivo (default payment next month)",
    xaxis_title="", yaxis_title="Número de clientes",
    height=450, width=650, showlegend=False,
)
fig.show()

prop_target


default_payment_next_month
0   0.7787
1   0.2213
Name: proportion, dtype: float64

Existe un **desbalance de clases**: aproximadamente **77.9% de los clientes no incurrieron en default (clase 0)** frente a **22.1% que sí (clase 1)**.Tener en cuenta que  cualquier modelo entrenado sin ajustes tenderá a favorecer la clase mayoritaria, por lo que conviene usar `class_weight="balanced"`, remuestreo  o umbrales de decisión ajustados, y evaluar con métricas robustas al desbalance (AUC-ROC, F1, recall de la clase 1) en vez de solo accuracy.


## Análisis Univariado

### 1.1 Estadísticos descriptivos completos

In [10]:
def resumen_univariado(serie):
    s = serie.dropna()
    q1, q3 = s.quantile(0.25), s.quantile(0.75)
    iqr = q3 - q1
    lim_inf, lim_sup = q1 - 1.5 * iqr, q3 + 1.5 * iqr
    outliers_pct = ((s < lim_inf) | (s > lim_sup)).mean() * 100
    return pd.Series({
        "n": s.shape[0],
        "media": s.mean(),
        "mediana": s.median(),
        "desv_estandar": s.std(),
        "min": s.min(),
        "Q1": q1,
        "Q3": q3,
        "max": s.max(),
        "IQR": iqr,
        "asimetria (skew)": stats.skew(s),
        "curtosis": stats.kurtosis(s),
        "% outliers (Tukey)": outliers_pct,
    })

tabla_univariada = pd.DataFrame({col: resumen_univariado(df[col]) for col in num_cols}).T
tabla_univariada.round(3)


,n,media,mediana,desv_estandar,min,Q1,Q3,max,IQR,asimetria (skew),curtosis,% outliers (Tukey)
LIMIT_BAL,"29,965.0000","167,442.0050","140,000.0000","129,760.1350","10,000.0000","50,000.0000","240,000.0000","1,000,000.0000","190,000.0000",0.9930,0.5370,0.5570
AGE,"29,965.0000",35.4880,34.0000,9.2190,21.0000,28.0000,41.0000,79.0000,13.0000,0.7320,0.0440,0.9080
PAY_0,"29,965.0000",-0.0170,0.0000,1.1230,-2.0000,-1.0000,0.0000,8.0000,1.0000,0.7350,2.7290,10.4420
PAY_2,"29,965.0000",-0.1320,0.0000,1.1960,-2.0000,-1.0000,0.0000,8.0000,1.0000,0.7920,1.5770,14.7140
PAY_3,"29,965.0000",-0.1640,0.0000,1.1960,-2.0000,-1.0000,0.0000,8.0000,1.0000,0.8410,2.0910,14.0430
PAY_4,"29,965.0000",-0.2190,0.0000,1.1680,-2.0000,-1.0000,0.0000,8.0000,1.0000,1.0010,3.5080,11.7040
PAY_5,"29,965.0000",-0.2650,0.0000,1.1320,-2.0000,-1.0000,0.0000,8.0000,1.0000,1.0090,4.0030,9.9020
PAY_6,"29,965.0000",-0.2890,0.0000,1.1490,-2.0000,-1.0000,0.0000,8.0000,1.0000,0.9490,3.4360,10.2720
BILL_AMT1,"29,965.0000","51,283.0100","22,438.0000","73,658.1320","-165,580.0000","3,595.0000","67,260.0000","964,511.0000","63,665.0000",2.6620,9.7950,7.9630
BILL_AMT2,"29,965.0000","49,236.3660","21,295.0000","71,195.5670","-69,777.0000","3,010.0000","64,109.0000","983,931.0000","61,099.0000",2.7040,10.2910,7.9760


In [11]:
tabla_categorica = pd.DataFrame({
    col: df[col].value_counts(normalize=True).sort_index().round(4) for col in cat_cols
})
tabla_categorica


,SEX,EDUCATION,MARRIAGE
1,0.3963,0.3525,0.4553
2,0.6037,0.4678,0.5321
3,NaN,0.1640,0.0126
4,NaN,0.0156,NaN


### 1.2 Visualización interactiva

In [12]:
def fig_hist_box(dataframe, cols, height=560):
    n = len(cols)
    fig = make_subplots(rows=2, cols=1, shared_xaxes=True,
                         row_heights=[0.72, 0.28], vertical_spacing=0.04)
    for i, col in enumerate(cols):
        fig.add_trace(go.Histogram(x=dataframe[col], marker_color=DEEP_NAVY,
                                    visible=(i == 0), showlegend=False), row=1, col=1)
        fig.add_trace(go.Box(x=dataframe[col], name="", marker_color=WARM_GOLD,
                              visible=(i == 0), showlegend=False, boxpoints=False), row=2, col=1)
    botones = []
    for i, col in enumerate(cols):
        vis = [False] * (2 * n)
        vis[2 * i], vis[2 * i + 1] = True, True
        botones.append(dict(label=col, method="update",
                             args=[{"visible": vis}, {"title": f"Distribución de {col}"}]))
    fig.update_layout(
        title=f"Distribución de {cols[0]}", height=height, width=850,
        updatemenus=[dict(buttons=botones, direction="down", x=1.15, y=1.05, showactive=True)],
    )
    fig.update_xaxes(title_text="", row=1, col=1)
    fig.update_xaxes(title_text=cols[0], row=2, col=1)
    return fig

In [13]:
# Interpretaciones de la sección 1.2 (variables numéricas). Los números se toman de
# `tabla_univariada` para que el texto siempre coincida con la tabla.
def nt(x):
    return f"-NT${abs(x):,.0f}" if x < 0 else f"NT${x:,.0f}"

PAY_COLS = ["PAY_0", "PAY_2", "PAY_3", "PAY_4", "PAY_5", "PAY_6"]
BILL_COLS = [f"BILL_AMT{i}" for i in range(1, 7)]
PAYAMT_COLS = [f"PAY_AMT{i}" for i in range(1, 7)]
MESES_ANTES = {"PAY_0": 0, **{f"PAY_{k}": k - 1 for k in range(2, 7)},
               **{f"BILL_AMT{k}": k - 1 for k in range(1, 7)}, **{f"PAY_AMT{k}": k - 1 for k in range(1, 7)}}

def corresp(col):
    n = MESES_ANTES[col]
    return "al mes más reciente" if n == 0 else ("al mes anterior al más reciente" if n == 1 else f"a {n} meses antes del más reciente")

U = tabla_univariada
skew_max_global = U["asimetria (skew)"].idxmax()
out_pay = U.loc[PAY_COLS, "% outliers (Tukey)"]
skew_bill = U.loc[BILL_COLS, "asimetria (skew)"]
min_bill = U.loc[BILL_COLS, "min"]

def tecnica_uni(col):
    s = U.loc[col]
    sk, ku, out = s["asimetria (skew)"], s["curtosis"], s["% outliers (Tukey)"]
    if col == "LIMIT_BAL":
        return (f"Histograma fuertemente sesgado a la derecha (asimetría {sk:.2f}); la mayoría de los clientes se concentra "
                f"entre {nt(s['Q1'])} y {nt(s['Q3'])} (rango intercuartílico), con una cola larga hasta {nt(s['max'])}; el boxplot "
                f"marca pocos outliers Tukey ({out:.1f}%) porque el criterio subestima el sesgo en variables tan asimétricas.")
    if col == "AGE":
        return (f"Distribución razonablemente simétrica (asimetría {sk:.2f}), concentrada entre {s['Q1']:.0f} y {s['Q3']:.0f} años "
                f"(mediana {s['mediana']:.0f}); cola derecha moderada hacia clientes mayores, con muy pocos outliers ({out:.1f}%).")
    if col in PAY_COLS:
        txt = (f"Variable discreta con la masa en 0 y -1 y una cola de atrasos de hasta {s['max']:.0f} meses; media {s['media']:.2f}, "
               f"mediana {s['mediana']:.0f}. El {out:.1f}% de los valores se marca como «outlier» bajo Tukey, un resultado artificial "
               f"de ser una variable discreta muy concentrada")
        if col == out_pay.idxmax():
            txt += " (la mayor proporción del bloque `PAY_x`)"
        elif col == out_pay.idxmin():
            txt += " (la menor proporción del bloque `PAY_x`)"
        txt += "."
        if col == "PAY_0":
            txt += " Es el mes más reciente del historial."
        else:
            prev = PAY_COLS[PAY_COLS.index(col) - 1]
            if s["media"] < U.loc[prev, "media"]:
                txt += f" La media es más negativa que la de `{prev}` ({U.loc[prev, 'media']:.2f}): cuanto más atrás en el tiempo, más clientes figuran al día."
        return txt
    if col in BILL_COLS:
        txt = (f"Histograma extremadamente sesgado a la derecha (asimetría {sk:.2f}, curtosis {ku:.1f}); la mediana ({nt(s['mediana'])}) queda "
               f"muy por debajo de la media ({nt(s['media'])}). Hay valores negativos (mínimo {nt(s['min'])}) que reflejan saldos a favor del "
               f"cliente; {out:.1f}% de outliers Tukey.")
        if col == skew_bill.idxmax():
            txt += f" Es la más asimétrica del bloque por un valor extremo de {nt(s['max'])} que estira la cola derecha."
        if col == min_bill.idxmin():
            txt += " Incluye el valor negativo más extremo del dataset."
        return txt
    txt = (f"Distribución muy concentrada en montos bajos (mediana {nt(s['mediana'])} frente a una media de {nt(s['media'])}), con asimetría "
           f"{sk:.1f} y curtosis {ku:,.0f} por unos pocos pagos muy grandes (máximo {nt(s['max'])}) que distorsionan el promedio.")
    if col == skew_max_global:
        txt += " Es la variable con mayor asimetría de todo el dataset."
    return txt

def basica_uni(col):
    s = U.loc[col]
    if col == "LIMIT_BAL":
        return (f"Es el cupo de crédito que el banco le dio a cada cliente. La mayoría tiene entre {nt(s['Q1'])} y {nt(s['Q3'])}. "
                f"Pocos clientes tienen cupos muy altos (hasta {nt(s['max'])}), por eso el gráfico se estira hacia la derecha.")
    if col == "AGE":
        return (f"Casi todos los clientes tienen entre {s['Q1']:.0f} y {s['Q3']:.0f} años y la edad típica es {s['mediana']:.0f}. "
                f"A partir de ahí hay cada vez menos clientes a medida que aumenta la edad.")
    if col in PAY_COLS:
        base = ("Indica qué tan al día estaba el cliente con sus pagos: de 1 en adelante son meses de atraso, -1 es pago puntual, y -2 y 0 "
                "(que la fuente no define con claridad) se interpretan como clientes sin atraso. ")
        if col == "PAY_0":
            return base + "Corresponde al mes más reciente. La gran mayoría está al día; una minoría se atrasa y unos pocos llegan a 8 meses de atraso."
        return (f"Es el mismo dato que `PAY_0` (meses de atraso; -2, -1 y 0 son sin atraso), pero correspondiente {corresp(col)}. "
                "Tiene la misma forma: casi todos al día y pocos con atrasos largos. Cuanto más atrás en el tiempo, más clientes aparecen al día.")
    if col in BILL_COLS:
        return (f"Es lo que el cliente debía según su estado de cuenta correspondiente {corresp(col)}. La mitad de los clientes debe menos de {nt(s['mediana'])}, "
                f"pero unos pocos deben cifras enormes, por eso el gráfico se estira hacia la derecha. Algunos valores son negativos: "
                f"son clientes que pagaron de más y tienen saldo a favor.")
    return (f"Es lo que el cliente pagó, correspondiente {corresp(col)}. La mitad de los clientes pagó menos de {nt(s['mediana'])}; "
            f"unos pocos pagaron cifras enormes y por eso el promedio ({nt(s['media'])}) engaña: es mucho más alto que lo habitual.")

INTERP_UNI_NUM = {c: {"basica": basica_uni(c), "tecnica": tecnica_uni(c)} for c in num_cols}

In [14]:
fig = fig_hist_box(df, num_cols)
show_with_interpretation(fig, num_cols, INTERP_UNI_NUM)

In [15]:
def fig_bar_categ(dataframe, cols, height=460):
    n = len(cols)
    fig = go.Figure()
    for i, col in enumerate(cols):
        vc = dataframe[col].value_counts().sort_index()
        fig.add_trace(go.Bar(x=vc.index.astype(str), y=vc.values, marker_color=NAVY,
                              visible=(i == 0), showlegend=False,
                              hovertemplate=col + ": %{x}<br>Frecuencia: %{y:,}<extra></extra>"))
    botones = []
    for i, col in enumerate(cols):
        vis = [False] * n
        vis[i] = True
        botones.append(dict(label=col, method="update",
                             args=[{"visible": vis}, {"title": f"Frecuencia de {col}", "xaxis.title": col}]))
    fig.update_layout(
        title=f"Frecuencia de {cols[0]}", height=height, width=750,
        xaxis_title=cols[0], yaxis_title="Frecuencia",
        updatemenus=[dict(buttons=botones, direction="down", x=1.2, y=1.05, showactive=True)],
    )
    return fig

In [16]:
# Interpretaciones de la sección 1.2 (variables categóricas), calculadas con `tabla_categorica`.
P = tabla_categorica
INTERP_UNI_CAT = {
    "SEX": {
        "basica": f"Hay más mujeres ({P.loc[2, 'SEX']:.0%}) que hombres ({P.loc[1, 'SEX']:.0%}) entre los clientes.",
        "tecnica": (f"El {P.loc[2, 'SEX']:.1%} de los clientes son mujeres (código 2) y el {P.loc[1, 'SEX']:.1%} hombres (código 1); "
                    f"la muestra está desbalanceada hacia el género femenino."),
    },
    "EDUCATION": {
        "basica": (f"Casi la mitad de los clientes ({P.loc[2, 'EDUCATION']:.0%}) tiene estudios universitarios, {P.loc[1, 'EDUCATION']:.0%} llegó a posgrado "
                   f"y {P.loc[3, 'EDUCATION']:.0%} a secundaria. La categoría «otros» es muy pequeña ({P.loc[4, 'EDUCATION']:.1%})."),
        "tecnica": (f"Tras reagrupar las categorías no oficiales, «universidad» concentra el {P.loc[2, 'EDUCATION']:.1%} de los clientes, "
                    f"«posgrado» el {P.loc[1, 'EDUCATION']:.1%}, «secundaria» el {P.loc[3, 'EDUCATION']:.1%} y «otros» apenas el {P.loc[4, 'EDUCATION']:.1%}."),
    },
    "MARRIAGE": {
        "basica": (f"Hay más solteros ({P.loc[2, 'MARRIAGE']:.0%}) que casados ({P.loc[1, 'MARRIAGE']:.0%}). Otros estados civiles son muy pocos "
                   f"({P.loc[3, 'MARRIAGE']:.1%})."),
        "tecnica": (f"Distribución bastante pareja entre «soltero» ({P.loc[2, 'MARRIAGE']:.1%}) y «casado» ({P.loc[1, 'MARRIAGE']:.1%}), "
                    f"con «otros» siendo marginal ({P.loc[3, 'MARRIAGE']:.1%})."),
    },
}

In [17]:
fig = fig_bar_categ(df, cat_cols)
show_with_interpretation(fig, cat_cols, INTERP_UNI_CAT)

## Análisis Bivariado

### 2.1 Pruebas de hipótesis y comparación de grupos

In [18]:
resultados_bivariado = []
for col in num_cols:
    g0 = df.loc[df[target] == 0, col]
    g1 = df.loc[df[target] == 1, col]
    u_stat, u_p = stats.mannwhitneyu(g0, g1, alternative="two-sided")
    t_stat, t_p = stats.ttest_ind(g0, g1, equal_var=False)
    resultados_bivariado.append({
        "variable": col,
        "media_no_default": g0.mean(), "media_default": g1.mean(),
        "mediana_no_default": g0.median(), "mediana_default": g1.median(),
        "Mann-Whitney U": u_stat, "p-value (MW)": u_p,
        "t (Welch)": t_stat, "p-value (t)": t_p,
    })

tabla_bivariada = pd.DataFrame(resultados_bivariado).set_index("variable")
tabla_bivariada.round(4)


,media_no_default,media_default,mediana_no_default,mediana_default,Mann-Whitney U,p-value (MW),t (Welch),p-value (t)
variable,,,,,,,,
LIMIT_BAL,"178,084.5082","129,984.5671","150,000.0000","90,000.0000","95,604,367.5000",0.0000,29.0232,0.0000
AGE,35.4210,35.7235,34.0000,34.0000,"76,836,623.5000",0.4035,-2.2729,0.0231
PAY_0,-0.2114,0.6682,0.0000,1.0000,"48,007,100.0000",0.0000,-48.6032,0.0000
PAY_2,-0.3000,0.4599,0.0000,0.0000,"55,916,535.5000",0.0000,-38.6861,0.0000
PAY_3,-0.3143,0.3633,0.0000,0.0000,"58,119,944.0000",0.0000,-34.5159,0.0000
PAY_4,-0.3538,0.2557,0.0000,0.0000,"60,396,772.5000",0.0000,-30.9956,0.0000
PAY_5,-0.3877,0.1689,0.0000,0.0000,"61,969,014.5000",0.0000,-28.8593,0.0000
PAY_6,-0.4038,0.1131,0.0000,0.0000,"63,412,765.5000",0.0000,-26.6696,0.0000
BILL_AMT1,"52,058.7202","48,552.8131","23,242.0000","20,209.5000","80,109,327.0000",0.0000,3.4155,0.0006


In [19]:
resultados_chi2 = []
for col in cat_cols:
    tabla_cruzada = pd.crosstab(df[col], df[target])
    chi2, p, dof, _ = stats.chi2_contingency(tabla_cruzada)
    resultados_chi2.append({"variable": col, "chi2": chi2, "p-value": p, "grados_libertad": dof})

tabla_chi2 = pd.DataFrame(resultados_chi2).set_index("variable")
tabla_chi2.round(6)


,chi2,p-value,grados_libertad
variable,,,
SEX,47.1311,0.0000,1
EDUCATION,160.4603,0.0000,3
MARRIAGE,27.4887,0.0000,2


Con 30,000 observaciones, casi cualquier diferencia entre grupos resulta estadísticamente significativa (p aproximadamente 0 en prácticamente todas las variables numéricas y en las tres categóricas vía chi-cuadrado), así que el p-value por sí solo aporta poco para priorizar variables. Lo relevante es la **magnitud** de la diferencia entre medias/medianas y las tasas de default por categoría, que se exploran en los gráficos siguientes.


### 2.2 Visualizaciones segmentadas por default

In [20]:
def fig_box_target(dataframe, cols, target_col, height=520):
    n = len(cols)
    fig = go.Figure()
    d0 = dataframe[dataframe[target_col] == 0]
    d1 = dataframe[dataframe[target_col] == 1]
    for i, col in enumerate(cols):
        fig.add_trace(go.Box(y=d0[col], name="No default", marker_color=DEEP_NAVY,
                              visible=(i == 0), showlegend=(i == 0), boxpoints=False, offsetgroup=0))
        fig.add_trace(go.Box(y=d1[col], name="Default", marker_color=WARM_GOLD,
                              visible=(i == 0), showlegend=(i == 0), boxpoints=False, offsetgroup=1))
    botones = []
    for i, col in enumerate(cols):
        vis = [False] * (2 * n)
        vis[2 * i], vis[2 * i + 1] = True, True
        botones.append(dict(label=col, method="update",
                             args=[{"visible": vis}, {"title": f"{col} según default", "yaxis.title": col}]))
    fig.update_layout(
        title=f"{cols[0]} según default", height=height, width=750, yaxis_title=cols[0],
        updatemenus=[dict(buttons=botones, direction="down", x=1.25, y=1.05, showactive=True)],
        legend_title_text="",
    )
    return fig

In [21]:
# Interpretaciones de la sección 2.2 (variables numéricas segmentadas por default), calculadas con `tabla_bivariada`.
B = tabla_bivariada

def sig(p):
    return "p<0.001" if p < 0.001 else f"p={p:.3f}"

def veredicto(pmw, pt):
    if max(pmw, pt) < 0.001:
        return "diferencia pequeña pero estadísticamente significativa"
    if max(pmw, pt) < 0.05:
        return "diferencia pequeña, significativa con ambas pruebas"
    if min(pmw, pt) < 0.05:
        return "evidencia débil: solo una de las dos pruebas la detecta"
    return "sin diferencia significativa entre grupos"

gap0 = B.loc["PAY_0", "media_default"] - B.loc["PAY_0", "media_no_default"]
ratio_pagos = (B.loc[PAYAMT_COLS, "media_default"] / B.loc[PAYAMT_COLS, "media_no_default"])

def tecnica_biv(col):
    r = B.loc[col]
    m0, m1, md0, md1 = r["media_no_default"], r["media_default"], r["mediana_no_default"], r["mediana_default"]
    pmw, pt = r["p-value (MW)"], r["p-value (t)"]
    if col == "LIMIT_BAL":
        return (f"Diferencia de negocio clara: media {nt(m0)} en no-default vs {nt(m1)} en default (mediana {md0:,.0f} vs {md1:,.0f}); "
                f"diferencia altamente significativa ({sig(pmw)}, Mann-Whitney). Un banco tiende a otorgar límites más altos a clientes de "
                f"menor riesgo percibido, y ese menor límite se confirma como señal de mayor riesgo real.")
    if col == "AGE":
        txt = f"Apenas difiere entre grupos ({m0:.1f} vs {m1:.1f} años, medianas {md0:.0f} y {md1:.0f}); Mann-Whitney {sig(pmw)}"
        txt += (", no significativo" if pmw >= 0.05 else ", significativo") + f" (Welch {sig(pt)}: con ~30,000 filas hasta diferencias mínimas pueden salir significativas; "
        txt += f"la diferencia práctica es de {abs(m1 - m0):.1f} años). Por sí sola aporta poca capacidad discriminante."
        return txt
    if col in PAY_COLS:
        gap = m1 - m0
        txt = f"Media {m0:.2f} (al día) en no-default vs {m1:.2f} (con atraso) en default; mediana {md0:.0f} vs {md1:.0f}; Mann-Whitney {sig(pmw)}."
        if col == "PAY_0":
            txt += " Es la variable con la separación más nítida entre grupos y el mejor predictor individual de default."
        elif gap < gap0:
            txt += f" La brecha de medias ({gap:.2f}) es menor que la de `PAY_0` ({gap0:.2f}): la señal se atenúa cuanto más antiguo es el mes."
        return txt
    if col in BILL_COLS:
        txt = f"Media {nt(m0)} en no-default vs {nt(m1)} en default (mediana {md0:,.0f} vs {md1:,.0f}); Mann-Whitney {sig(pmw)}, Welch {sig(pt)}: {veredicto(pmw, pt)}."
        if m1 < m0 and min(pmw, pt) < 0.05:
            txt += " Los clientes que luego caen en default facturan algo menos."
        return txt
    ratio = m1 / m0
    txt = (f"Media {nt(m0)} en no-default vs {nt(m1)} en default: los clientes que luego caen en default pagan, en promedio, solo el {ratio:.0%} "
           f"de lo que pagan los demás (mediana {md0:,.0f} vs {md1:,.0f}); diferencia altamente significativa (Mann-Whitney {sig(pmw)}).")
    if col == ratio_pagos.idxmin():
        txt += " Es la mayor brecha relativa del bloque `PAY_AMT`."
    return txt

def basica_biv(col):
    r = B.loc[col]
    m0, m1 = r["media_no_default"], r["media_default"]
    pmw, pt = r["p-value (MW)"], r["p-value (t)"]
    if col == "LIMIT_BAL":
        return (f"Los clientes que después no pagan tenían, en promedio, un cupo de crédito más bajo (cerca de NT${m1 / 1000:,.0f} mil) que quienes sí "
                f"pagan (cerca de NT${m0 / 1000:,.0f} mil). Un cupo bajo es una señal de riesgo.")
    if col == "AGE":
        return (f"La edad casi no ayuda a distinguir: quienes caen en default y quienes no tienen prácticamente la misma edad "
                f"(unos {(m0 + m1) / 2:.0f} años en ambos grupos).")
    if col == "PAY_0":
        return ("Es la señal más clara de todas: quienes terminan en default venían, por lo general, con atrasos en el último mes, "
                "mientras que quienes no caen en default venían al día.")
    if col in PAY_COLS:
        return (f"Cuenta la misma historia que `PAY_0`, pero con el estado de pago correspondiente {corresp(col)}: quienes caen en default ya venían con atrasos. "
                "La señal es un poco más débil cuanto más antiguo es el mes.")
    if col in BILL_COLS:
        if max(pmw, pt) < 0.05:
            return "Casi no ayuda a distinguir: quienes caen en default debían montos parecidos (algo menores) a los de quienes no caen."
        return "No ayuda a distinguir: ambos grupos debían montos parecidos en ese mes."
    ratio = m1 / m0
    return (f"Es una señal fuerte: por cada NT$100 que paga un cliente que no cae en default, quien termina en default paga unos NT${ratio * 100:.0f}. "
            f"Quienes después caen en default ya venían pagando mucho menos.")

INTERP_BIV_NUM = {c: {"basica": basica_biv(c), "tecnica": tecnica_biv(c)} for c in num_cols}

In [22]:
fig = fig_box_target(df, num_cols, target)
show_with_interpretation(fig, num_cols, INTERP_BIV_NUM)

In [23]:
def fig_rate_by_categ(dataframe, cols, target_col, height=460):
    n = len(cols)
    fig = go.Figure()
    tasa_global = dataframe[target_col].mean()
    for i, col in enumerate(cols):
        tab = dataframe.groupby(col)[target_col].mean().sort_index()
        fig.add_trace(go.Bar(x=tab.index.astype(str), y=tab.values, marker_color=WARM_GOLD,
                              visible=(i == 0), showlegend=False,
                              hovertemplate=col + ": %{x}<br>Tasa de default: %{y:.1%}<extra></extra>"))
    botones = []
    for i, col in enumerate(cols):
        vis = [False] * n
        vis[i] = True
        botones.append(dict(label=col, method="update",
                             args=[{"visible": vis}, {"title": f"Tasa de default por {col}", "xaxis.title": col}]))
    fig.update_layout(
        title=f"Tasa de default por {cols[0]}", height=height, width=750,
        xaxis_title=cols[0], yaxis_title="Tasa de default", yaxis_tickformat=".0%",
        updatemenus=[dict(buttons=botones, direction="down", x=1.2, y=1.05, showactive=True)],
    )
    fig.add_hline(y=tasa_global, line_dash="dash", line_color=NAVY,
                  annotation_text=f"Tasa global {tasa_global:.1%}", annotation_position="top left")
    return fig

In [24]:
# Interpretaciones de la sección 2.2 (tasa de default por categoría), calculadas con los datos y `tabla_chi2`.
tasas = {c: df.groupby(c)[target].mean() for c in cat_cols}
share = {c: df[c].value_counts(normalize=True) for c in cat_cols}

def chi_txt(c):
    r = tabla_chi2.loc[c]
    return f"χ²={r['chi2']:.1f}, {sig(r['p-value'])}"

T = tasas
INTERP_BIV_CAT = {
    "SEX": {
        "basica": (f"Los hombres caen en default un poco más que las mujeres: {T['SEX'][1] * 100:.0f} de cada 100 hombres frente a "
                   f"{T['SEX'][2] * 100:.0f} de cada 100 mujeres."),
        "tecnica": (f"Los hombres tienen una tasa de default de {T['SEX'][1]:.1%} frente a {T['SEX'][2]:.1%} en mujeres; "
                    f"diferencia significativa ({chi_txt('SEX')})."),
    },
    "EDUCATION": {
        "basica": (f"Quienes llegaron a posgrado caen menos en default ({T['EDUCATION'][1] * 100:.0f} de cada 100) que quienes tienen universidad "
                   f"({T['EDUCATION'][2] * 100:.0f}) o secundaria ({T['EDUCATION'][3] * 100:.0f}). El grupo «otros» tiene la tasa más baja "
                   f"({T['EDUCATION'][4] * 100:.0f} de cada 100), pero son muy pocos clientes, así que no conviene sacar conclusiones fuertes de él."),
        "tecnica": (f"La tasa de default es más alta en clientes con secundaria ({T['EDUCATION'][3]:.1%}) y universidad ({T['EDUCATION'][2]:.1%}) que en "
                    f"posgrado ({T['EDUCATION'][1]:.1%}); la categoría «otros» muestra la tasa más baja de todas ({T['EDUCATION'][4]:.1%}), aunque "
                    f"representa solo el {share['EDUCATION'][4]:.1%} de la muestra; diferencia muy significativa ({chi_txt('EDUCATION')})."),
    },
    "MARRIAGE": {
        "basica": (f"Los casados ({T['MARRIAGE'][1] * 100:.0f} de cada 100) y la categoría «otros» ({T['MARRIAGE'][3] * 100:.0f}) caen en default un poco más "
                   f"que los solteros ({T['MARRIAGE'][2] * 100:.0f}). La diferencia existe, pero es pequeña."),
        "tecnica": (f"Diferencia más moderada: «casado» ({T['MARRIAGE'][1]:.1%}) y «otros» ({T['MARRIAGE'][3]:.1%}) tienen tasas similares, algo por "
                    f"encima de «soltero» ({T['MARRIAGE'][2]:.1%}); significativa ({chi_txt('MARRIAGE')}) pero de menor magnitud práctica que "
                    f"`EDUCATION` o `SEX`."),
    },
}

In [25]:
fig = fig_rate_by_categ(df, cat_cols, target)
show_with_interpretation(fig, cat_cols, INTERP_BIV_CAT)

## Multicolinealidad

### 3.1 Matriz de correlación

Antes de calcular la correlación se **capan (winsorizan) los percentiles 1 y 99** de cada variable numérica. Esto evita que un puñado de valores extremos (p. ej. `BILL_AMT` o `LIMIT_BAL` en la cola superior) distorsione el coeficiente de correlación, un problema que no se controló en la versión anterior del EDA.


In [26]:
def winsorize(serie, lower=0.01, upper=0.99):
    lo, hi = serie.quantile(lower), serie.quantile(upper)
    return serie.clip(lo, hi)

df_w = df[num_cols].apply(winsorize)

corr_pearson = df_w.corr(method="pearson")
corr_spearman = df_w.corr(method="spearman")

fig = go.Figure(data=go.Heatmap(
    z=corr_pearson.values, x=corr_pearson.columns, y=corr_pearson.columns,
    colorscale=DIVERGING_NG, zmid=0, zmin=-1, zmax=1,
    text=corr_pearson.round(2).values, texttemplate="%{text}", textfont=dict(size=8),
    hovertemplate="%{y} vs %{x}<br>correlación: %{z:.3f}<extra></extra>",
))
fig.update_layout(
    title="Matriz de correlación entre variables independientes (Pearson, winsorizada)",
    height=700, width=820,
    updatemenus=[dict(
        type="buttons", direction="right", x=0.5, y=1.1, showactive=True,
        buttons=[
            dict(label="Pearson", method="update",
                 args=[{"z": [corr_pearson.values], "text": [corr_pearson.round(2).values]},
                       {"title": "Matriz de correlación (Pearson, winsorizada)"}]),
            dict(label="Spearman", method="update",
                 args=[{"z": [corr_spearman.values], "text": [corr_spearman.round(2).values]},
                       {"title": "Matriz de correlación (Spearman, winsorizada)"}]),
        ],
    )],
)
fig.show()


Las seis variables de facturación (**`BILL_AMT1` a `BILL_AMT6`**) están **muy correlacionadas entre sí** (Pearson entre 0.81 y 0.95): tiene sentido, ya que el saldo de un mes está fuertemente relacionado con el saldo del mes siguiente si el cliente no paga el total. Las variables `PAY_0` a `PAY_6` también muestran correlación moderada-alta entre sí (miden el mismo fenómeno atraso en el pago en distintos meses). En cambio, los montos efectivamente pagados (`PAY_AMT*`) están débilmente correlacionados tanto entre sí como con el resto de variables. Esto ya anticipa un problema de multicolinealidad entre las variables de facturación, que se confirma con el VIF a continuación.


### 3.2 Factor de Inflación de la Varianza (VIF)

In [27]:
X_vif = df_w.copy()
X_vif = (X_vif - X_vif.mean()) / X_vif.std()
X_vif = X_vif.assign(const=1.0)

vif_data = pd.DataFrame({
    "variable": num_cols,
    "VIF": [variance_inflation_factor(X_vif.values, i) for i in range(len(num_cols))],
}).sort_values("VIF", ascending=False)

fig = px.bar(
    vif_data, x="VIF", y="variable", orientation="h",
    color="VIF", color_continuous_scale=[NAVY, PALE_GOLD, WARM_GOLD],
    title="Factor de Inflación de la Varianza (VIF) por variable (datos winsorizados)",
)
fig.add_vline(x=5, line_dash="dash", line_color=NAVY, annotation_text="VIF = 5")
fig.add_vline(x=10, line_dash="dash", line_color=WARM_GOLD, annotation_text="VIF = 10")
fig.update_layout(height=550, width=850, yaxis_title="", xaxis_title="VIF", coloraxis_showscale=False)
fig.show()

vif_data.round(2)


,variable,VIF
12,BILL_AMT5,24.9600
9,BILL_AMT2,24.5800
10,BILL_AMT3,21.4800
11,BILL_AMT4,21.2900
13,BILL_AMT6,14.7900
8,BILL_AMT1,13.2600
6,PAY_5,4.4600
5,PAY_4,4.1000
4,PAY_3,3.6400
3,PAY_2,3.1700


El VIF confirma lo que insinuaba la matriz de correlación: **`BILL_AMT2` a `BILL_AMT5` superan un VIF de 20**, muy por encima del umbral habitual de 10, y `BILL_AMT1`/`BILL_AMT6` rondan 13-15, evidencia fuerte de multicolinealidad severa entre las seis variables de facturación. Las variables `PAY_x` tienen un VIF moderado (3-4.5), por debajo del umbral de alerta pero mostrando cierta redundancia entre sí. El resto de variables (`LIMIT_BAL`, `AGE`, `PAY_AMT*`) tiene VIF cercano a 1-2, sin problema relevante.

Para un modelo lineal (regresión logística), conviene **no usar las seis `BILL_AMT` por separado**: alternativas razonables son quedarse solo con `BILL_AMT1` (el más reciente), construir un promedio o una pendiente/tendencia de los 6 meses, o aplicar una reducción de dimensionalidad (PCA) sobre ese bloque de variables. Para modelos basados en árboles (como el Random Forest usado en la Parte 4), la multicolinealidad afecta menos la performance predictiva, aunque sigue diluyendo la importancia atribuida a cada variable individual.


### 3.3 Coordenadas paralelas: interacción conjunta entre las variables de facturación

In [28]:
bill_cols = [c for c in num_cols if c.startswith("BILL_AMT")]
muestra_pc = df_w.sample(n=2000, random_state=42)

fig = go.Figure(data=go.Parcoords(
    line=dict(
        color=df.loc[muestra_pc.index, target],
        colorscale=[[0, DEEP_NAVY], [1, WARM_GOLD]],
        showscale=True,
        colorbar=dict(title="Default", tickvals=[0, 1], ticktext=["No", "Sí"]),
    ),
    dimensions=[dict(label=c, values=muestra_pc[c]) for c in bill_cols],
))
fig.update_layout(title="Coordenadas paralelas: montos de facturación (BILL_AMT), coloreado por default",
                   height=480, width=900)
fig.show()


El gráfico de coordenadas paralelas confirma visualmente el hallazgo del VIF: las líneas se mueven de forma casi paralela entre `BILL_AMT1` y `BILL_AMT6`, es decir, un cliente con saldo alto en un mes casi siempre lo tiene alto en los meses adyacentes. No se observa un patrón de color (default vs no default) claramente diferenciado a lo largo de estas seis variables, lo que refuerza el insight bivariado de que el **monto adeudado por sí solo discrimina poco** entre clientes que caen en default y los que no; lo que sí discrimina, como se vio en la Parte 2, es el estado de pago (`PAY_x`).


## PARTE 4: Interpretabilidad Avanzada con SHAP

In [29]:
feature_cols = num_cols + cat_cols
X = df[feature_cols].copy()
y = df[target].copy()

X_train, X_test, y_train, y_test = train_test_split(
    X, y, test_size=0.3, random_state=42, stratify=y
)

modelo_rf = RandomForestClassifier(
    n_estimators=200, max_depth=6, min_samples_leaf=50,
    class_weight="balanced", random_state=42, n_jobs=-1,
)
modelo_rf.fit(X_train, y_train)

# Muestra para SHAP (el cálculo exacto sobre 30,000 filas es costoso; una muestra representativa basta para el EDA)
X_shap = X_test.sample(n=2000, random_state=42)

explainer = shap.TreeExplainer(modelo_rf)
shap_values = explainer.shap_values(X_shap)

# shap_values puede venir como lista [clase0, clase1] o como array 3D según la versión de shap/sklearn
if isinstance(shap_values, list):
    sv_clase1 = shap_values[1]
elif shap_values.ndim == 3:
    sv_clase1 = shap_values[:, :, 1]
else:
    sv_clase1 = shap_values

sv_df = pd.DataFrame(sv_clase1, columns=feature_cols, index=X_shap.index)
sv_df.shape


(2000, 23)

### 4.1 Importancia global (mean |SHAP|)

In [30]:
importancia = sv_df.abs().mean().sort_values(ascending=True)

fig = go.Figure(go.Bar(
    x=importancia.values, y=importancia.index, orientation="h",
    marker_color=DEEP_NAVY,
    hovertemplate="%{y}<br>|SHAP| medio: %{x:.4f}<extra></extra>",
))
fig.update_layout(
    title="Importancia global de variables (media de |SHAP|)",
    height=650, width=800, xaxis_title="Media de |Valor SHAP|", yaxis_title="",
)
fig.show()


`PAY_0` (estado de pago del mes más reciente) domina claramente el ranking de importancia, muy por encima de cualquier otra variable, coherente con lo observado en el análisis bivariado. Le siguen a distancia `PAY_2`, `PAY_3`, `PAY_4` (estado de pago de meses anteriores) y `LIMIT_BAL`. Las variables de facturación (`BILL_AMT*`) y las demográficas (`AGE`, `SEX`, `EDUCATION`, `MARRIAGE`) aportan comparativamente poco al modelo. Esto sugiere que, si se buscara un modelo más simple, priorizar las variables `PAY_x` y `LIMIT_BAL` capturaría la mayor parte de la señal predictiva.


### 4.2 Beeswarm interactivo (todas las variables)

In [31]:
orden = importancia.index[::-1]  # de mayor a menor importancia

rng = np.random.default_rng(42)
fig = go.Figure()
for i, col in enumerate(orden):
    vals = X_shap[col].values.astype(float)
    if np.nanstd(vals) > 0:
        percentil = pd.Series(vals).rank(pct=True).values
    else:
        percentil = np.full(len(vals), 0.5)
    y_base = len(orden) - i
    jitter = (rng.random(len(vals)) - 0.5) * 0.7
    fig.add_trace(go.Scatter(
        x=sv_df[col].values, y=y_base + jitter,
        mode="markers",
        marker=dict(
            size=4, color=percentil, colorscale=[[0, NAVY], [1, WARM_GOLD]],
            showscale=(i == 0),
            colorbar=dict(title="Valor de la<br>variable (percentil)", x=1.02) if i == 0 else None,
            opacity=0.65, line=dict(width=0),
        ),
        name=col, showlegend=False,
        hovertemplate=col + "<br>SHAP: %{x:.4f}<extra></extra>",
    ))

fig.update_layout(
    title="Beeswarm SHAP: importancia y dirección del efecto por variable",
    height=750, width=900,
    yaxis=dict(tickvals=list(range(len(orden), 0, -1)), ticktext=list(orden), title=""),
    xaxis_title="Valor SHAP (impacto en la probabilidad de default)",
)
fig.add_vline(x=0, line_dash="dash", line_color="gray")
fig.show()


El beeswarm añade la *dirección* del efecto al ranking de importancia: los puntos dorados (valores altos de la variable) de `PAY_0`, `PAY_2` y `PAY_3` se concentran del lado derecho (SHAP positivo → empujan hacia default), mientras que los puntos azul marino (valores bajos/negativos, es decir, pagos al día) se concentran del lado izquierdo (SHAP negativo → empujan hacia no-default). En `LIMIT_BAL` el patrón es inverso: valores altos (dorado) empujan hacia SHAP negativo (menor riesgo), consistente con el insight de negocio de la sección bivariada. Para las variables de facturación y las demográficas, la nube de puntos está mucho más concentrada cerca de cero y sin un patrón de color claro, confirmando su bajo poder predictivo individual.


### 4.3 Gráfico de dependencia 

In [32]:
fig = go.Figure()
n_vars = len(num_cols)

for i, col in enumerate(num_cols):
    corrs = corr_pearson[col].drop(col).abs()
    col_interaccion = corrs.idxmax()
    fig.add_trace(go.Scatter(
        x=X_shap[col], y=sv_df[col],
        mode="markers",
        marker=dict(size=6, color=X_shap[col_interaccion], colorscale=[[0, NAVY], [1, WARM_GOLD]],
                    showscale=True, colorbar=dict(title=col_interaccion)),
        customdata=X_shap[col_interaccion],
        hovertemplate=(col + ": %{x:.2f}<br>SHAP: %{y:.4f}<br>" +
                        col_interaccion + ": %{customdata:.2f}<extra></extra>"),
        visible=(i == 0), name=col,
    ))

botones = []
for i, col in enumerate(num_cols):
    vis = [False] * n_vars
    vis[i] = True
    botones.append(dict(label=col, method="update", args=[{"visible": vis}, {"xaxis.title": col}]))

fig.update_layout(
    title=f"SHAP dependence plot: {num_cols[0]}",
    height=550, width=950,
    xaxis_title=num_cols[0], yaxis_title="Valor SHAP",
    updatemenus=[dict(buttons=botones, direction="down", x=1.2, y=1.0, showactive=True)],
)
fig.add_hline(y=0, line_dash="dash", line_color="gray")
fig.show()


### 4.4 Interpretabilidad

- El ranking de importancia SHAP confirma lo observado en el análisis bivariado: el **estado de pago más reciente (`PAY_0`)** y sus rezagos (`PAY_2`, `PAY_3`, `PAY_4`) son, con diferencia, las variables que más empujan la predicción de default, seguidas de `LIMIT_BAL`.
- El beeswarm permite ver la *dirección* del efecto: atrasos (valores altos, en dorado) en las variables `PAY_x` empujan el SHAP hacia la derecha (mayor probabilidad de default), mientras que valores altos de `LIMIT_BAL` lo empujan hacia la izquierda (menor riesgo).
- Los gráficos de dependencia permiten detectar **no linealidades**: el efecto marginal de pasar de "al día" (0 o -1) a "1 mes de atraso" en `PAY_0` es mucho mayor que el de pasar de 4 a 5 meses de atraso, información que un coeficiente lineal único (como en una regresión logística simple sobre la variable sin transformar) no podría capturar, y que justifica tratar `PAY_x` como variable categórica/ordinal con dummies, o usar modelos no lineales.
- Las variables de facturación (`BILL_AMT*`) muestran valores SHAP cercanos a cero en casi todo su rango, reforzando la recomendación de la Parte 3 de no usarlas todas por separado en un modelo lineal: aportan poca señal individual y además están fuertemente correlacionadas entre sí.


## PARTE 5: Preprocesamiento: resolución de los hallazgos

Cada hallazgo de las partes anteriores se resuelve aquí con una decisión explícita. La lógica vive en `src/preprocessing.py` (`build_final_dataset`), de modo que el mismo código sirve para regenerar el dataset desde el archivo original. El resultado se guarda en `data/processed/dataset_final.csv`, que es lo que leen los notebooks de modelado.

| # | Hallazgo del EDA | Resolución | Dónde |
|---|---|---|---|
| 1 | 35 filas duplicadas | Se eliminan (una sola vez, antes de cualquier partición) | EDA y `build_final_dataset` |
| 2 | Códigos no documentados en `EDUCATION` (0, 5, 6) y `MARRIAGE` (0) | Se reagrupan en «Otros» | EDA y `build_final_dataset` |
| 3 | Saldos de facturación negativos (1,930 clientes) | Se conservan por ser válidos y se resumen en `N_CREDIT_BALANCE_MONTHS` | `build_final_dataset` |
| 4 | Asimetría extrema y outliers en `LIMIT_BAL`, `PAY_AMT1-6` (asimetría de hasta 30; pagos de más de NT$1.6 millones) | Log con signo; las columnas quedan con sufijo `_LOG` | `build_final_dataset` |
| 5 | Multicolinealidad severa en `BILL_AMT1-6` (VIF hasta ~25) | Se reemplazan por `BILL_AMT_MEAN_6M_LOG` (nivel) y `BILL_AMT_TREND_6M_LOG` (tendencia) | `build_final_dataset` |
| 6 | Desbalance de clases (77.9% / 22.1%) | No se toca el dataset: se maneja dentro de la validación cruzada (`class_weight`, SMOTE, ADASYN) y se evalúa con F1 y AUC-ROC | `balancing.py`, `config.DEFAULT_SCORING` |
| 7 | Variables categóricas sin codificar (`SEX`, `EDUCATION`, `MARRIAGE`) y escalas muy distintas | One-hot y `StandardScaler` (solo para KNN, SVM y regresión logística), ajustados únicamente con el fold de entrenamiento | `build_column_transformer` |
| 8 | Códigos -2 y 0 de `PAY_x` con definición ambigua en la fuente | Se conservan tal cual (decisión del EDA); queda documentado como limitación | EDA |
| 9 | Relación no lineal entre `PAY_x` y el riesgo | `PAY_x` se mantiene como variable ordinal y se compara con modelos que capturan no linealidad (árboles, Random Forest, XGBoost, SVM, KNN) | Pipeline de modelos |
| 10 | Grupos de filas con las mismas variables pero distinto resultado | Ruido irreducible: se cuantifica y se documenta, no se corrige | Sección 5.2 |
| 11 | Sin valores nulos | No se requiere imputación | EDA |

Los puntos 1 a 5 se transforman en el dataset. El 6 y el 7 deben ir dentro del pipeline de validación porque aprenden de los datos y, si se aplicaran antes de partir, filtrarían información del fold de validación.

### 5.1 Construcción del dataset final

In [33]:
from src import preprocessing as pp
from src.data_loader import load_processed_dataset

raw = pp.load_raw_dataset()
final, reporte = pp.build_final_dataset(raw)

resumen = pd.Series({
    "Filas en el archivo original": reporte["filas_entrada"],
    "Duplicados exactos eliminados": reporte["filas_duplicadas_eliminadas"],
    "Filas en el dataset final": reporte["filas_salida"],
    "Filas con códigos EDUCATION no documentados reagrupados": reporte["filas_reasignadas_a_otros"]["EDUCATION"],
    "Filas con código MARRIAGE no documentado reagrupadas": reporte["filas_reasignadas_a_otros"]["MARRIAGE"],
    "Clientes con al menos un saldo de facturación negativo": reporte["filas_con_factura_negativa"],
    "Grupos con las mismas variables pero distinto resultado": reporte["grupos_con_etiqueta_conflictiva"],
    "Columnas en el dataset final (incluye el target)": final.shape[1],
}, name="valor")
resumen.to_frame()

,valor
Filas en el archivo original,30000
Duplicados exactos eliminados,35
Filas en el dataset final,29965
Filas con códigos EDUCATION no documentados reagrupados,345
Filas con código MARRIAGE no documentado reagrupadas,54
Clientes con al menos un saldo de facturación negativo,1930
Grupos con las mismas variables pero distinto resultado,21
Columnas en el dataset final (incluye el target),21


### 5.2 Efecto de las transformaciones

In [34]:
transformadas = {"LIMIT_BAL": "LIMIT_BAL_LOG", **{f"PAY_AMT{i}": f"PAY_AMT{i}_LOG" for i in range(1, 7)}}
filas = []
for antes, despues in transformadas.items():
    filas.append({
        "variable original": antes, "variable final": despues,
        "asimetría antes": stats.skew(df[antes]), "asimetría después": stats.skew(final[despues]),
        "máximo / mediana antes": df[antes].max() / df[antes].median(),
        "máximo / mediana después": final[despues].max() / final[despues].median(),
    })
tabla_transformacion = pd.DataFrame(filas).set_index("variable original")
tabla_transformacion.round(2)

,variable final,asimetría antes,asimetría después,máximo / mediana antes,máximo / mediana después
variable original,,,,,
LIMIT_BAL,LIMIT_BAL_LOG,0.9900,-0.5100,7.1400,1.1700
PAY_AMT1,PAY_AMT1_LOG,14.6600,-1.3000,415.5800,1.7900
PAY_AMT2,PAY_AMT2_LOG,30.4400,-1.2400,837.9400,1.8800
PAY_AMT3,PAY_AMT3_LOG,17.2100,-1.0800,496.7000,1.8300
PAY_AMT4,PAY_AMT4_LOG,12.9000,-0.9700,414.0000,1.8200
PAY_AMT5,PAY_AMT5_LOG,11.1200,-0.9400,284.3500,1.7700
PAY_AMT6,PAY_AMT6_LOG,10.6300,-0.8600,352.4400,1.8000


In [35]:
derivadas_bill = [pp.BILL_MEAN_COLUMN, pp.BILL_TREND_COLUMN, pp.CREDIT_BALANCE_COLUMN]
print("Variables derivadas del bloque BILL_AMT (reemplazan a BILL_AMT1-6):")
print(final[derivadas_bill].describe().round(2).to_string())
print()
print("Correlación entre las derivadas (Pearson):")
print(final[derivadas_bill].corr().round(2).to_string())

Variables derivadas del bloque BILL_AMT (reemplazan a BILL_AMT1-6):
       BILL_AMT_MEAN_6M_LOG  BILL_AMT_TREND_6M_LOG  N_CREDIT_BALANCE_MONTHS
count           29,965.0000            29,965.0000              29,965.0000
mean                 9.3400                 1.7300                   0.1300
std                  2.6700                 7.1500                   0.6100
min                -10.9300               -11.5100                   0.0000
25%                  8.4900                -6.4100                   0.0000
50%                  9.9600                 5.4000                   0.0000
75%                 10.9500                 8.3300                   0.0000
max                 13.6800                11.8100                   6.0000

Correlación entre las derivadas (Pearson):
                         BILL_AMT_MEAN_6M_LOG  BILL_AMT_TREND_6M_LOG  N_CREDIT_BALANCE_MONTHS
BILL_AMT_MEAN_6M_LOG                   1.0000                 0.1000                  -0.3600
BILL_AMT_TREND_6

In [36]:
num_final = [c for c in final.columns if c not in cat_cols + [target]]
X_vif_final = final[num_final].apply(winsorize)
X_vif_final = (X_vif_final - X_vif_final.mean()) / X_vif_final.std()
X_vif_final = X_vif_final.assign(const=1.0)

vif_final = pd.DataFrame({
    "variable": num_final,
    "VIF": [variance_inflation_factor(X_vif_final.values, i) for i in range(len(num_final))],
}).sort_values("VIF", ascending=False)

fig = px.bar(
    vif_final, x="VIF", y="variable", orientation="h",
    color="VIF", color_continuous_scale=[NAVY, PALE_GOLD, WARM_GOLD],
    title="VIF por variable tras el preprocesamiento (mismo método que la sección 3.2)",
)
fig.add_vline(x=5, line_dash="dash", line_color=NAVY, annotation_text="VIF = 5")
fig.add_vline(x=10, line_dash="dash", line_color=WARM_GOLD, annotation_text="VIF = 10")
fig.update_layout(height=550, width=850, yaxis_title="", xaxis_title="VIF", coloraxis_showscale=False)
fig.show()

print(f"VIF máximo antes: {vif_data['VIF'].max():.1f} ({vif_data.iloc[0]['variable']})  ->  después: {vif_final['VIF'].max():.1f} ({vif_final.iloc[0]['variable']})")

VIF máximo antes: 25.0 (BILL_AMT5)  ->  después: 5.8 (PAY_5)


### 5.3 Verificación de que cada hallazgo quedó resuelto

In [37]:
# Cada fila verifica que un hallazgo quedó resuelto. Si alguna falla, la celda lanza un error.
feature_cols_final = [c for c in final.columns if c != target]
comparables = cat_cols + ["AGE"] + PAY_COLS
verificaciones = {
    "Sin valores nulos": int(final.isnull().sum().sum()) == 0,
    "Sin filas duplicadas (hallazgo 1)": int(final.duplicated().sum()) == 0,
    "Mismas filas que el EDA tras eliminar duplicados": len(final) == len(df),
    "Variables sin transformar idénticas a las del EDA, fila por fila":
        bool((final[comparables + [target]].to_numpy() == df[comparables + [target]].to_numpy()).all()),
    "EDUCATION solo toma valores 1-4 (hallazgo 2)": set(final["EDUCATION"].unique()) <= {1, 2, 3, 4},
    "MARRIAGE solo toma valores 1-3 (hallazgo 2)": set(final["MARRIAGE"].unique()) <= {1, 2, 3},
    "SEX solo toma valores 1-2": set(final["SEX"].unique()) <= {1, 2},
    "Saldos negativos resumidos en una variable derivada (hallazgo 3)":
        int((final[pp.CREDIT_BALANCE_COLUMN] > 0).sum()) == reporte["filas_con_factura_negativa"],
    "|asimetría| de las variables con log menor a 1.5 (hallazgo 4)":
        bool((tabla_transformacion["asimetría después"].abs() < 1.5).all()),
    "BILL_AMT1-6 originales reemplazadas (hallazgo 5)": not any(c in final.columns for c in pp.BILL_COLUMNS),
    "VIF máximo menor a 10 (hallazgo 5)": bool(vif_final["VIF"].max() < 10),
    "Sin columna ID": "ID" not in final.columns,
    "Target binario y con la misma proporción de default":
        set(final[target].unique()) == {0, 1} and abs(final[target].mean() - df[target].mean()) < 1e-12,
    "Target es la última columna": final.columns[-1] == target,
    "Las categóricas del pipeline existen en el dataset (config.CATEGORICAL_COLUMNS)": set(config.CATEGORICAL_COLUMNS) <= set(final.columns),
}
tabla_verificacion = pd.DataFrame({"verificación": list(verificaciones), "resultado": ["OK" if v else "FALLA" for v in verificaciones.values()]}).set_index("verificación")
fallas = [k for k, v in verificaciones.items() if not v]
assert not fallas, f"Hallazgos sin resolver: {fallas}"
tabla_verificacion

,resultado
verificación,
Sin valores nulos,OK
Sin filas duplicadas (hallazgo 1),OK
Mismas filas que el EDA tras eliminar duplicados,OK
"Variables sin transformar idénticas a las del EDA, fila por fila",OK
EDUCATION solo toma valores 1-4 (hallazgo 2),OK
MARRIAGE solo toma valores 1-3 (hallazgo 2),OK
SEX solo toma valores 1-2,OK
Saldos negativos resumidos en una variable derivada (hallazgo 3),OK
|asimetría| de las variables con log menor a 1.5 (hallazgo 4),OK


Con las verificaciones aprobadas, el dataset se guarda y se vuelve a leer con el mismo cargador que usan los notebooks de modelado.

In [38]:
config.PROCESSED_DATA_PATH.parent.mkdir(parents=True, exist_ok=True)
final.to_csv(config.PROCESSED_DATA_PATH, index=False)

# Releer lo guardado, tal como lo hacen los notebooks de modelado, y comprobar que es idéntico
recargado = load_processed_dataset()
pd.testing.assert_frame_equal(recargado, final, check_dtype=False)
print(f"Guardado en: {config.PROCESSED_DATA_PATH.relative_to(config.PROJECT_ROOT)}")
print(f"Dimensiones: {recargado.shape} | target: {config.TARGET_COLUMN} | proporción de default: {recargado[config.TARGET_COLUMN].mean():.4f}")
recargado.head()

Guardado en: data\processed\dataset_final.csv
Dimensiones: (29965, 21) | target: default_payment_next_month | proporción de default: 0.2213


,SEX,EDUCATION,MARRIAGE,AGE,PAY_0,PAY_2,PAY_3,PAY_4,PAY_5,PAY_6,...,BILL_AMT_TREND_6M_LOG,N_CREDIT_BALANCE_MONTHS,LIMIT_BAL_LOG,PAY_AMT1_LOG,PAY_AMT2_LOG,PAY_AMT3_LOG,PAY_AMT4_LOG,PAY_AMT5_LOG,PAY_AMT6_LOG,default_payment_next_month
0,2,2,1,24,2,2,-1,-1,-2,-2,...,6.7400,0,9.9035,0.0000,6.5367,0.0000,0.0000,0.0000,0.0000,1
1,2,2,2,26,-1,2,0,0,0,2,...,-5.5169,0,11.6953,0.0000,6.9088,6.9088,6.9088,0.0000,7.6014,1
2,2,2,2,34,0,0,0,0,0,0,...,7.5260,0,11.4076,7.3258,7.3139,6.9088,6.9088,6.9088,8.5174,0
3,2,2,1,37,0,0,0,0,0,0,...,8.4647,0,10.8198,7.6014,7.6109,7.0909,7.0040,6.9754,6.9088,0
4,1,2,1,57,-1,0,-1,0,0,0,...,-7.7109,0,10.8198,7.6014,10.5100,9.2104,9.1051,6.5367,6.5221,0


### 5.4 Qué recibe el modelado

El dataset final tiene **29,965 filas y 21 columnas**: 20 variables predictoras y el target (`default_payment_next_month`, siempre la última columna).

- **Categóricas** (`SEX`, `EDUCATION`, `MARRIAGE`): se mantienen como enteros y el pipeline las convierte a one-hot dentro de la validación cruzada.
- **Numéricas originales sin cambios**: `AGE` y `PAY_0`, `PAY_2` a `PAY_6`.
- **Numéricas transformadas**: `LIMIT_BAL_LOG` y `PAY_AMT1_LOG` a `PAY_AMT6_LOG`.
- **Derivadas del bloque de facturación**: `BILL_AMT_MEAN_6M_LOG`, `BILL_AMT_TREND_6M_LOG` y `N_CREDIT_BALANCE_MONTHS`.

Dos cosas que conviene tener presentes al modelar: (1) los códigos -2 y 0 de `PAY_x` siguen siendo ambiguos en la fuente, así que cualquier conclusión que dependa de la frontera exacta entre ellos debe leerse con cautela; (2) hay 21 grupos de clientes con las mismas variables pero distinto resultado, un ruido que ningún modelo puede explicar, lo que pone un techo natural al desempeño alcanzable.

## Conclusiones generales del EDA

- **Calidad de datos**: el dataset no tiene valores nulos. Las 35 filas duplicadas se eliminan y las categorías no oficiales de `EDUCATION` y `MARRIAGE` se reagrupan en "Otros". Los códigos -2 y 0 de las variables `PAY_x` tienen una definición ambigua en la fuente original, una limitación a tener en cuenta al comunicar resultados.
- **Desbalance de clases**: ~78% no-default vs ~22% default. Se aborda en el modelamiento, dentro de la validación cruzada (`class_weight`, remuestreo), con métricas robustas al desbalance.
- **Mejor variable predictora, por lejos**: el estado de pago del mes más reciente (`PAY_0`), seguido de los meses anteriores y del límite de crédito (`LIMIT_BAL`). Las variables demográficas (`AGE`, `SEX`, `EDUCATION`, `MARRIAGE`) aportan señal, pero mucho más débil.
- **Multicolinealidad severa** entre las seis variables de facturación (`BILL_AMT1`-`BILL_AMT6`, VIF hasta ~25): se resuelven reemplazándolas por su nivel medio y su tendencia, con lo que el VIF máximo del dataset final queda por debajo de 10 (Parte 5).
- **Variables muy asimétricas** (`LIMIT_BAL`, `PAY_AMT*`): se transforman con log con signo (Parte 5).
- **Recomendación para el modelamiento**: dada la relación no lineal entre atrasos y riesgo (vista en los dependence plots), un modelo basado en árboles (Random Forest, Gradient Boosting) es una opción natural, como ya lo sugiere el buen desempeño cualitativo del Random Forest usado para SHAP. Si se prefiere un modelo lineal por interpretabilidad, conviene categorizar/discretizar `PAY_x`.
- **Resultado final**: el dataset preprocesado queda guardado en `data/processed/dataset_final.csv` y todas las verificaciones de la sección 5.3 pasan.